In [1]:
from pathlib import Path
import hashlib
import json
import sys

import numpy as np
import pandas as pd
import plotly.graph_objects as go
import plotly.io as pio
from plotly.subplots import make_subplots
from IPython.display import display, Markdown

ROOT = next(
    (path for path in (Path.cwd(), *Path.cwd().parents)
     if (path / "src/backward_pricer.py").is_file()),
    None,
)
if ROOT is None:
    raise FileNotFoundError("Open this notebook inside the local-vol-spx repository.")
if str(ROOT / "src") not in sys.path:
    sys.path.insert(0, str(ROOT / "src"))

from backward_pricer import BackwardVanillaPricer
from tailed_surface import TailedShortEndSurface

BASE_RUN = "spx_2023-09-01_combined_central"
CANDIDATE = "day_zero_weight_0p1"
MODEL_PATH = ROOT / "data/processed/surfaces" / BASE_RUN / CANDIDATE / "day_zero_surface.json"
PDE_DIR = ROOT / "outputs/pde_diagnostics" / BASE_RUN / CANDIDATE
BACKWARD_DIR = ROOT / "outputs/backward_pde_diagnostics" / CANDIDATE
BLACK_DIR = ROOT / "outputs/backward_pde_diagnostics/black_benchmark"

pio.templates.default = "plotly_white"
pio.renderers.default = "plotly_mimetype"
pd.set_option("display.max_columns", 20)
pd.set_option("display.precision", 7)
print("Repository:", ROOT)

Repository: /Users/pranayvij/GitHub/local-vol-spx


In [2]:
def read_json(path):
    return json.loads(path.read_text())

def file_hash(path):
    return hashlib.sha256(path.read_bytes()).hexdigest()

def verify_inputs(audit):
    for name, expected in audit["input_sha256"].items():
        path = Path(name)
        if not path.is_absolute():
            path = ROOT / path
        if not path.is_file() or file_hash(path) != expected:
            raise ValueError(f"Missing or changed input: {path}. Rebuild its diagnostics.")

model_spec = read_json(MODEL_PATH)
tails_path = (MODEL_PATH.parent / model_spec["tail_slices_file"]).resolve()
tail_spec = read_json(tails_path)
pde_audit = read_json(PDE_DIR / "day_zero_audit.json")
backward_audit = read_json(BACKWARD_DIR / "backward_audit.json")
for audit in (pde_audit, backward_audit):
    verify_inputs(audit)
if file_hash(MODEL_PATH) not in backward_audit["input_sha256"].values():
    raise ValueError("Backward diagnostics were generated from a different model.")
if file_hash(tails_path) not in pde_audit["input_sha256"].values():
    raise ValueError("Forward diagnostics were generated from different tails.")

surface = TailedShortEndSurface.load(MODEL_PATH)
quotes = pd.read_csv(PDE_DIR / "quote_repricing.csv")
market = pd.read_csv(BACKWARD_DIR / "price_and_greeks.csv")
bumps = pd.read_csv(BACKWARD_DIR / "spot_bump_checks.csv")
market_summary = pd.read_csv(BACKWARD_DIR / "convergence_summary.csv")
black_summary = pd.read_csv(BLACK_DIR / "convergence_summary.csv")
space = pd.read_csv(PDE_DIR / "space_convergence.csv")
time_grid = pd.read_csv(PDE_DIR / "time_convergence.csv")
domains = pd.read_csv(PDE_DIR / "domain_sensitivity.csv")
boundaries = pd.read_csv(PDE_DIR / "boundary_sensitivity.csv")

display(Markdown("**Current candidate:** " + str(tails_path.relative_to(ROOT))))
display(pd.DataFrame({"Value": {
    "Spot": surface.spot,
    "Fitted expiry pillars": len(tail_spec["slices"]),
    "Retained calibration quotes": len(quotes),
    "First fitted maturity, days": 365.0 * surface.first_maturity,
    "Last maturity, days": 365.0 * surface.maturities[-1],
    "Finest backward spatial intervals": market["space_intervals"].max(),
    "Greek convention": "Local-volatility function and carry held fixed",
    "Day-zero sampled peak local vol, %": pde_audit["max_day_zero_local_volatility_pct"],
    "First-expiry left sampled peak local vol, %": pde_audit["max_first_expiry_left_local_volatility_pct"],
}}))

**Current candidate:** data/processed/surfaces/spx_2023-09-01_combined_central/first_expiry_conditioning/weight_0p1/tail_slices.json

,Value
Spot,4516.02
Fitted expiry pillars,10
Retained calibration quotes,1157
"First fitted maturity, days",4.0
"Last maturity, days",60.0
Finest backward spatial intervals,3200
Greek convention,Local-volatility function and carry held fixed
"Day-zero sampled peak local vol, %",1343.3877314
"First-expiry left sampled peak local vol, %",1612.2272093


In [3]:
tail_rows = pd.DataFrame(tail_spec["slices"])
tail_rows["days"] = 365.0 * tail_rows["maturity_years"]
fit_summary = quotes.groupby("expiry").agg(
    quotes=("strike", "size"),
    candidate_rms_half_spreads=("candidate_residual_half_spreads", lambda s: np.sqrt(np.mean(s**2))),
    pde_rms_half_spreads=("pde_residual_half_spreads", lambda s: np.sqrt(np.mean(s**2))),
    outside_original_bands=("candidate_residual_half_spreads", lambda s: int((s.abs() > 1.0 + 1e-8).sum())),
    max_numerical_price_error=("pde_minus_candidate_points", lambda s: s.abs().max()),
).reset_index()
display(tail_rows[["expiry", "days", "left_log_moneyness", "right_log_moneyness"]].merge(fit_summary, on="expiry"))
calendar = pd.DataFrame(surface.surface.calendar_checks())
display(calendar)
display(Markdown(
    "The spline core lies between each pair of joins. Outside them, prices use constructed tails. "
    "Quote-fit residuals measure calibration; PDE-minus-candidate differences measure numerical consistency. "
    "Calendar checks concern the constructed positive-maturity slices."
))

,expiry,days,left_log_moneyness,right_log_moneyness,quotes,candidate_rms_half_spreads,pde_rms_half_spreads,outside_original_bands,max_numerical_price_error
0,2023-09-05,4.0,-0.0386,0.0161936,103,1.3310358,1.3067177,35,0.0084782
1,2023-09-08,7.0,-0.0826,0.0373002,116,0.7333326,0.7352478,14,0.0070426
2,2023-09-12,11.0,-0.0900,0.0602037,108,0.8508592,0.8532923,22,0.0062225
3,2023-09-14,13.0,-0.0900,0.0499908,107,0.7730012,0.7722786,17,0.0059201
4,2023-09-22,21.0,-0.0900,0.0900000,127,0.8404040,0.8410499,27,0.0056102
5,2023-09-29,28.0,-0.0900,0.0900000,170,0.7816502,0.7841839,23,0.0054193
6,2023-10-06,35.0,-0.0900,0.0900000,120,0.6609330,0.6610007,11,0.0051896
7,2023-10-13,42.0,-0.0900,0.0900000,78,0.8083608,0.8096650,17,0.0061910
8,2023-10-27,56.0,-0.0900,0.0900000,49,0.5619495,0.5618214,4,0.0091810
9,2023-10-31,60.0,-0.0900,0.0900000,179,0.6847810,0.6874891,29,0.0107719


,earlier_days,later_days,region,left_tail_ordered,left_log_coefficient_change,left_log_ratio_at_common_join,right_tail_ordered,right_log_coefficient_change,right_log_ratio_at_common_join,middle_status,middle_intervals_checked,minimum_evaluated_middle_gap,minimum_accepted_middle_bound,passed
0,4.0,7.0,all,True,0.0787874,1.0862724,True,0.0087916,1.0199067,passed,21,0.0000118,0.0000118,True
1,7.0,11.0,all,True,0.0377373,0.7286256,True,0.0100412,0.6372568,passed,39,0.0000079,0.0000079,True
2,11.0,13.0,all,True,0.5264695,0.5283027,True,0.6504462,0.5760832,passed,37,0.0000130,0.0000130,True
3,13.0,21.0,all,True,0.3301978,0.8357494,True,0.0067220,0.6260694,passed,31,0.0000112,0.0000112,True
4,21.0,28.0,all,True,0.4784885,0.5331545,True,0.0890199,0.4033712,passed,39,0.0000119,0.0000033,True
5,28.0,35.0,all,True,0.4200806,0.3937833,True,0.3110318,0.5096039,passed,39,0.0000239,0.0000095,True
6,35.0,42.0,all,True,0.3943705,0.3156003,True,0.7874206,0.5093456,passed,39,0.0000398,0.0000171,True
7,42.0,56.0,all,True,0.5972449,0.4777720,True,0.5054334,0.7486731,passed,23,0.0001110,0.0001110,True
8,56.0,60.0,all,True,0.1376790,0.0954534,True,0.2401875,0.1756579,passed,49,0.0000405,0.0000264,True


The spline core lies between each pair of joins. Outside them, prices use constructed tails. Quote-fit residuals measure calibration; PDE-minus-candidate differences measure numerical consistency. Calendar checks concern the constructed positive-maturity slices.

In [4]:
PLOT_Y_MIN, PLOT_Y_MAX = -0.09, 0.09
Y_POINTS, TIME_POINTS = 101, 41
if not surface.min_log_moneyness <= PLOT_Y_MIN < PLOT_Y_MAX <= surface.max_log_moneyness:
    raise ValueError("Plot range exceeds the model domain.")
y = np.linspace(PLOT_Y_MIN, PLOT_Y_MAX, Y_POINTS)
z = np.exp(y)
pillars = surface.maturities[surface.maturities > 0.0]
extra = np.linspace(min(0.25 / 365.0, pillars[0]), pillars[-1], TIME_POINTS)
extra = [t for t in extra if not np.any(np.isclose(t, pillars, rtol=0.0, atol=1e-12))]
times = np.sort(np.concatenate([pillars, extra]))
iv_matrix, lv_matrix = [], []
for t in times:
    iv_matrix.append(surface.implied_volatility(surface.forward(t) * z, float(t)))
    variance = np.asarray(surface.normalized_variance(z, float(t), "right"))
    if not np.all(np.isfinite(variance)) or np.any(variance < 0.0):
        raise ValueError(f"Invalid local variance at {365.0*t:g} days.")
    lv_matrix.append(np.sqrt(variance))
iv_matrix, lv_matrix = np.asarray(iv_matrix), np.asarray(lv_matrix)

jump_rows = []
for t in pillars[:-1]:
    left = np.sqrt(surface.normalized_variance(z, float(t), "left"))
    right = np.sqrt(surface.normalized_variance(z, float(t), "right"))
    difference = 100.0 * (right - left)
    index = int(np.argmax(np.abs(difference)))
    jump_rows.append({"days": 365.0*t, "max_sampled_jump_pp": abs(difference[index]),
                      "signed_jump_pp": difference[index], "log_moneyness": y[index]})
display(pd.DataFrame(jump_rows))
display(Markdown(
    "These grids are evaluated from the loaded candidate. Local volatility uses the right-hand value at pillars "
    "and the available interior value at the last maturity. The 3D plot connects samples; the table above "
    "shows the one-sided jumps. Zero-time implied volatility is excluded."
))

,days,max_sampled_jump_pp,signed_jump_pp,log_moneyness
0,4.0,258.4174014,-258.4174014,-0.0900
1,7.0,37.7955136,37.7955136,-0.0738
2,11.0,51.8944194,51.8944194,-0.0864
3,13.0,14.0925183,-14.0925183,0.0900
4,21.0,5.4528712,5.4528712,-0.0900
5,28.0,9.7490616,9.7490616,0.0810
6,35.0,3.1458998,3.1458998,0.0900
7,42.0,3.8848567,3.8848567,0.0792
8,56.0,1.8938738,-1.8938738,-0.0306


These grids are evaluated from the loaded candidate. Local volatility uses the right-hand value at pillars and the available interior value at the last maturity. The 3D plot connects samples; the table above shows the one-sided jumps. Zero-time implied volatility is excluded.

In [5]:
for title, values, colors in (
    ("Implied volatility (%)", 100.0 * iv_matrix, "Viridis"),
    ("Local volatility (%)", 100.0 * lv_matrix, "Cividis"),
):
    fig = go.Figure(go.Surface(
        x=y, y=365.0*times, z=values, colorscale=colors,
        colorbar={"title": "%"},
        hovertemplate="Log-moneyness: %{x:.4f}<br>Days: %{y:.2f}<br>Vol: %{z:.3f}%<extra></extra>",
    ))
    fig.update_layout(
        title=f"{title}: current candidate, including constructed regions",
        height=550,
        scene={"xaxis_title": "Forward log-moneyness", "yaxis_title": "Days",
               "zaxis_title": title},
        margin={"l": 20, "r": 20, "b": 20, "t": 65},
    )
    fig.show()

In [6]:
display(Markdown(
    "**Black:** differences from exact analytical values. **SPX:** price errors compare with the fitted candidate; "
    "Greek changes compare with the finest computed grid. A zero finest-grid difference is a reference convention."
))
display(black_summary)
display(market_summary)
fig = make_subplots(rows=2, cols=3, subplot_titles=(
    "Black price error", "Black delta error", "Black gamma error",
    "SPX price change vs finest", "SPX delta change vs finest", "SPX gamma change vs finest",
))
for column, metric in enumerate(("price", "delta", "gamma"), start=1):
    exact = "max_price_error_points" if metric == "price" else f"max_{metric}_error"
    for row, frame, field in (
        (1, black_summary, exact),
        (2, market_summary, f"max_{metric}_change_vs_finest"),
    ):
        selected = frame[frame[field] > 0.0]
        fig.add_trace(go.Scatter(x=selected["space_intervals"], y=selected[field], mode="lines+markers"), row, column)
        fig.update_xaxes(type="log", title_text="Spatial intervals", row=row, col=column)
        fig.update_yaxes(type="log", title_text="Absolute difference", row=row, col=column)
fig.update_layout(height=650, showlegend=False)
fig.show()

**Black:** differences from exact analytical values. **SPX:** price errors compare with the fitted candidate; Greek changes compare with the finest computed grid. A zero finest-grid difference is a reference convention.

,space_intervals,max_price_error_points,max_delta_error,max_gamma_error,max_price_change_vs_finest,max_delta_change_vs_finest,max_gamma_change_vs_finest
0,400,0.0008792,0.0000575,0.0000101,0.0008242,0.0000539,0.0000095
1,800,0.0002198,0.0000144,0.0000025,0.0001648,0.0000108,0.0000019
2,1600,0.0000549,0.0000036,0.0000006,0.0000000,0.0000000,0.0000000


,space_intervals,max_price_error_points,max_delta_error,max_gamma_error,max_price_change_vs_finest,max_delta_change_vs_finest,max_gamma_change_vs_finest
0,800,0.2206877,NaN,NaN,0.2067477,0.0010800,0.0005914
1,1600,0.0582438,NaN,NaN,0.0443038,0.0005934,0.0001079
2,3200,0.0139400,NaN,NaN,0.0000000,0.0000000,0.0000000


In [7]:
counts = np.sort(market["space_intervals"].unique())
fine = market[market["space_intervals"] == counts[-1]].copy()
coarse = market[market["space_intervals"] == counts[-2]]
keys = ["days", "log_strike", "spot"]
comparison = fine.merge(
    coarse[keys + ["price", "delta", "gamma"]],
    on=keys, suffixes=("", "_previous"), validate="one_to_one",
)
comparison["absolute_price_error"] = comparison["price_error_points"].abs()
comparison["price_error_pct"] = 100.0 * comparison["absolute_price_error"] / comparison["target_price"].abs().replace(0.0, np.nan)
for metric in ("delta", "gamma"):
    change = (comparison[metric] - comparison[f"{metric}_previous"]).abs()
    comparison[f"{metric}_change"] = change
    comparison[f"{metric}_change_pct"] = 100.0 * change / comparison[metric].abs().replace(0.0, np.nan)
display(comparison[[
    "days", "log_strike", "price", "absolute_price_error", "price_error_pct",
    "delta", "delta_change", "delta_change_pct", "gamma", "gamma_change_pct",
]].sort_values("absolute_price_error", ascending=False))
display(Markdown(
    f"Greek changes compare {counts[-2]:,} with {counts[-1]:,} intervals, using the finest value as denominator. "
    "They are refinement diagnostics, not certified error bounds. Small option prices and small deltas "
    "can have substantial relative differences."
))

,days,log_strike,price,absolute_price_error,price_error_pct,delta,delta_change,delta_change_pct,gamma,gamma_change_pct
1,4.0,0.00,11.2663119,0.0139400,0.1235791,0.4816326,0.0000576,0.0119674,0.0139079,0.7761434
2,4.0,0.02,0.0495042,0.0039921,8.7714578,0.0057605,0.0005934,10.3016666,0.0006309,4.0019943
0,4.0,-0.02,89.6559847,0.0020578,0.0022952,0.9696397,0.0002229,0.0229893,0.0027088,1.3201171
8,60.0,0.02,41.0098299,0.0015662,0.0038192,0.2523301,0.0002408,0.0954215,0.0031660,0.0926739
5,35.0,0.02,21.5922593,0.0014813,0.0068608,0.2156250,0.0002168,0.1005618,0.0033732,0.1104280
6,60.0,-0.02,144.3314415,0.0011727,0.0008125,0.5169028,0.0001454,0.0281286,0.0041654,0.2014317
7,60.0,0.00,84.5422200,0.0006581,0.0007784,0.3903694,0.0001903,0.0487504,0.0038481,0.0805242
3,35.0,-0.02,122.9459658,0.0003416,0.0002778,0.5807095,0.0001339,0.0230657,0.0048326,0.2330112
4,35.0,0.00,61.3486532,0.0002424,0.0003950,0.4087470,0.0001617,0.0395510,0.0044918,0.0936068


Greek changes compare 1,600 with 3,200 intervals, using the finest value as denominator. They are refinement diagnostics, not certified error bounds. Small option prices and small deltas can have substantial relative differences.

In [8]:
display(bumps)
fig = make_subplots(rows=1, cols=2, subplot_titles=(
    "Delta: relative spot-bump difference (%)", "Gamma: relative spot-bump difference (%)",
))
for (day, log_strike, spot), group in bumps.groupby(["days", "log_strike", "spot"]):
    group = group.sort_values("bump_points")
    name = f"{day:g}d, y={log_strike:+.2f}"
    for column, metric in enumerate(("delta", "gamma"), start=1):
        relative = 100.0 * group[f"{metric}_difference"].abs() / group[metric].abs().replace(0.0, np.nan)
        positive = relative > 0.0
        fig.add_trace(go.Scatter(
            x=group.loc[positive, "bump_points"], y=relative[positive], mode="lines+markers",
            name=name, legendgroup=name, showlegend=(column == 1),
        ), 1, column)
        fig.update_xaxes(type="log", title_text="Spot bump, points", row=1, col=column)
        fig.update_yaxes(type="log", title_text="Relative difference, %", row=1, col=column)
fig.update_layout(height=450)
fig.show()
display(Markdown(
    "Finite differences and analytical derivatives here use the same solved price interpolant. "
    "Their agreement checks differentiation. Independent Black benchmarks and grid refinement provide "
    "separate evidence about numerical accuracy. Large bumps include higher-order spot effects."
))

,days,log_strike,spot,bump_points,delta,fd_delta,delta_difference,gamma,fd_gamma,gamma_difference
0,4.0,-0.02,4516.02,22.58010,0.9696397,0.9508380,-0.0188017,0.0027088,0.0032521,0.0005434
1,4.0,-0.02,4516.02,11.29005,0.9696397,0.9651042,-0.0045355,0.0027088,0.0028548,0.0001460
2,4.0,-0.02,4516.02,4.51602,0.9696397,0.9689242,-0.0007155,0.0027088,0.0027392,0.0000304
3,4.0,0.00,4516.02,22.58010,0.4816326,0.4850027,0.0033702,0.0139079,0.0133247,-0.0005832
4,4.0,0.00,4516.02,11.29005,0.4816326,0.4825593,0.0009268,0.0139079,0.0137571,-0.0001508
5,4.0,0.00,4516.02,4.51602,0.4816326,0.4817917,0.0001592,0.0139079,0.0138779,-0.0000300
6,4.0,0.02,4516.02,22.58010,0.0057605,0.0126826,0.0069221,0.0006309,0.0009410,0.0003101
7,4.0,0.02,4516.02,11.29005,0.0057605,0.0072390,0.0014785,0.0006309,0.0007052,0.0000743
8,4.0,0.02,4516.02,4.51602,0.0057605,0.0059868,0.0002263,0.0006309,0.0006461,0.0000152
9,35.0,-0.02,4516.02,22.58010,0.5807095,0.5752479,-0.0054616,0.0048326,0.0050665,0.0002339


Finite differences and analytical derivatives here use the same solved price interpolant. Their agreement checks differentiation. Independent Black benchmarks and grid refinement provide separate evidence about numerical accuracy. Large bumps include higher-order spot effects.

In [9]:
quotes["numerical_error_half_spreads"] = quotes["pde_minus_candidate_points"] / quotes["call_half_width"]
display(pd.DataFrame({"Value": {
    "Candidate quote RMS, half-spreads": np.sqrt(np.mean(quotes["candidate_residual_half_spreads"]**2)),
    "Forward PDE quote RMS, half-spreads": np.sqrt(np.mean(quotes["pde_residual_half_spreads"]**2)),
    "Numerical error RMS, half-spreads": np.sqrt(np.mean(quotes["numerical_error_half_spreads"]**2)),
    "Max numerical quote error, points": quotes["pde_minus_candidate_points"].abs().max(),
}}))
fig = make_subplots(rows=2, cols=2, subplot_titles=(
    "Forward spatial refinement", "Forward time refinement",
    "Domain sensitivity", "Numerical quote errors",
))
fig.add_trace(go.Scatter(x=space["space_intervals"], y=space["max_price_error_points"], mode="lines+markers", name="Space"), 1, 1)
fig.add_trace(go.Scatter(x=time_grid["steps_per_day"], y=time_grid["max_vs_time_reference_points"], mode="lines+markers", name="Time"), 1, 2)
fig.add_trace(go.Scatter(x=domains["domain_width"], y=domains["max_change_vs_narrow_domain_points"], mode="lines+markers", name="Domain"), 2, 1)
fig.add_trace(go.Scatter(x=boundaries["domain_width"], y=boundaries["max_boundary_policy_change_points"], mode="lines+markers", name="Boundary policy"), 2, 1)
for expiry, group in quotes.groupby("expiry"):
    fig.add_trace(go.Scatter(x=group["log_moneyness"], y=group["numerical_error_half_spreads"], mode="markers", name=expiry), 2, 2)
for column in (1, 2):
    fig.update_xaxes(type="log", row=1, col=column)
    fig.update_yaxes(type="log", title_text="Price difference, points", row=1, col=column)
fig.update_xaxes(title_text="Spatial intervals", row=1, col=1)
fig.update_xaxes(title_text="Steps per day", row=1, col=2)
fig.update_xaxes(title_text="Domain half-width", row=2, col=1)
fig.update_yaxes(title_text="Price difference, points", row=2, col=1)
fig.update_xaxes(title_text="Forward log-moneyness", row=2, col=2)
fig.update_yaxes(title_text="PDE minus candidate, half-spreads", row=2, col=2)
fig.update_layout(height=700)
fig.show()
display(Markdown(
    "These domain and boundary checks concern the saved forward solve. "
    "Backward Greek sensitivity to time resolution and boundary placement remains to be tested."
))

,Value
"Candidate quote RMS, half-spreads",0.8228320
"Forward PDE quote RMS, half-spreads",0.8205671
"Numerical error RMS, half-spreads",0.0528897
"Max numerical quote error, points",0.0107719


These domain and boundary checks concern the saved forward solve. Backward Greek sensitivity to time resolution and boundary placement remains to be tested.

In [10]:
OPTION_DAYS = 35.0
LOG_STRIKE = 0.0
OPTION_KIND = "call"
SPOT_BAND = 0.015

expiry = OPTION_DAYS / 365.0
strike = surface.forward(expiry) * np.exp(LOG_STRIKE)
width = float(backward_audit["domain_width"])
pricer = BackwardVanillaPricer(
    surface, -width, width, int(counts[-1]),
    max_time_step=1.0 / (365.0 * backward_audit["steps_per_day"]),
)
print(f"Solving one {OPTION_KIND}: {OPTION_DAYS:g} days, strike {strike:.4f}")
conditional = pricer.solve(strike, expiry, kind=OPTION_KIND)
spots = surface.spot * np.linspace(1.0 - SPOT_BAND, 1.0 + SPOT_BAND, 201)
values = conditional.greeks(spots)
at_spot = conditional.greeks(surface.spot)
target = float(surface.call_price(strike, expiry))
if OPTION_KIND == "put":
    target -= surface.discount_factor(expiry) * (surface.forward(expiry) - strike)
display(pd.DataFrame({"Value": {
    "Strike": strike, "Days": OPTION_DAYS,
    "PDE price": float(at_spot.price), "Candidate price": target,
    "Price difference, points": float(at_spot.price) - target,
    "Delta": float(at_spot.delta), "Gamma per index point": float(at_spot.gamma),
}}))
fig = make_subplots(rows=1, cols=3, subplot_titles=("Price", "Delta", "Gamma"))
for column, metric in enumerate(("price", "delta", "gamma"), start=1):
    fig.add_trace(go.Scatter(x=spots, y=getattr(values, metric), mode="lines", name=metric), 1, column)
    fig.add_vline(x=surface.spot, line_dash="dot", row=1, col=column)
    fig.update_xaxes(title_text="Spot, index points", row=1, col=column)
    fig.update_yaxes(title_text=metric.capitalize(), row=1, col=column)
fig.update_layout(height=400, showlegend=False, title="Fixed calibrated local-volatility function and carry")
fig.show()
display(Markdown(
    "Change the four settings at the top of this cell to explore another option. "
    "This cell performs one fresh PDE solve; the earlier diagnostics are loaded from disk. "
    "These Greeks do not yet represent sticky-delta or an empirically estimated minimum-variance hedge."
))

Solving one call: 35 days, strike 4534.1748


,Value
Strike,4534.1747525
Days,35.0000000
PDE price,61.3486532
Candidate price,61.3488955
"Price difference, points",-0.0002424
Delta,0.4087470
Gamma per index point,0.0044918


Change the four settings at the top of this cell to explore another option. This cell performs one fresh PDE solve; the earlier diagnostics are loaded from disk. These Greeks do not yet represent sticky-delta or an empirically estimated minimum-variance hedge.

In [11]:
from datetime import datetime, timezone
from plotly.colors import qualitative

DIAG_Y_MIN, DIAG_Y_MAX = -0.09, 0.09
DIAG_Y_POINTS = 2001
DIAG_DIR = ROOT / "outputs/model_conditioning" / BASE_RUN / CANDIDATE
DIAG_DIR.mkdir(parents=True, exist_ok=True)

for saved_audit in (pde_audit, backward_audit):
    verify_inputs(saved_audit)

diag_surface = surface
diag_pillars = diag_surface.surface.maturities

diag_joins = pd.DataFrame(tail_spec["slices"]).sort_values(
    "maturity_years"
).reset_index(drop=True)

diag_joins["days"] = 365.0 * diag_joins["maturity_years"]

if not (
    diag_surface.min_log_moneyness
    <= DIAG_Y_MIN
    < DIAG_Y_MAX
    <= diag_surface.max_log_moneyness
):
    raise ValueError("Diagnostic range exceeds the model domain.")

join_y = diag_joins[
    ["left_log_moneyness", "right_log_moneyness"]
].to_numpy().ravel()

extra_y = (
    join_y[:, None] + np.array([-1e-7, 0.0, 1e-7])
).ravel()

extra_y = extra_y[
    (extra_y >= DIAG_Y_MIN) & (extra_y <= DIAG_Y_MAX)
]

diag_y = np.unique(
    np.r_[
        np.linspace(DIAG_Y_MIN, DIAG_Y_MAX, DIAG_Y_POINTS),
        extra_y,
    ]
)
diag_z = np.exp(diag_y)

anchor_iv = np.asarray(
    diag_surface.implied_volatility(
        diag_surface.forward(diag_pillars[0]) * diag_z,
        float(diag_pillars[0]),
    )
)


def coefficient_regions(y_values, maturity, side):
    """Describe all slices contributing to local variance."""
    nearest = float(
        diag_pillars[np.argmin(abs(diag_pillars - maturity))]
    )
    if abs(nearest - maturity) < 1e-12:
        maturity = nearest

    short_end = (
        maturity < diag_pillars[0]
        or (
            maturity == diag_pillars[0]
            and side == "left"
        )
    )

    if short_end:
        indices = [0]
        prefix = "Short-end over "
    else:
        index = (
            np.searchsorted(diag_pillars, maturity, side=side)
            - 1
        )
        index = int(
            np.clip(index, 0, len(diag_pillars) - 2)
        )
        indices = [index, index + 1]
        prefix = ""

    masks = [
        (
            y_values
            >= diag_joins.loc[i, "left_log_moneyness"]
        )
        & (
            y_values
            <= diag_joins.loc[i, "right_log_moneyness"]
        )
        for i in indices
    ]

    core_count = np.sum(masks, axis=0)

    if len(indices) == 1:
        region = np.where(core_count == 1, "core", "tail")
    else:
        region = np.select(
            [core_count == 2, core_count == 1],
            ["both cores", "core + tail"],
            default="both tails",
        )

    region = np.array(
        [prefix + value for value in region]
    )
    sources = ", ".join(
        f"{diag_joins.loc[i, 'days']:g}d"
        for i in indices
    )
    return region, sources, indices


probe_cases = [(0.0, "right")]

probe_cases += [
    (day / 365.0, "right")
    for day in (0.25, 1.0)
    if day / 365.0 < diag_pillars[0]
]

probe_cases += [
    (float(t), side)
    for t in diag_pillars[:4]
    for side in ("left", "right")
]

if diag_pillars[0] < 35.0 / 365.0 < diag_pillars[-1]:
    nearest = float(
        diag_pillars[
            np.argmin(abs(diag_pillars - 35.0 / 365.0))
        ]
    )
    time_35 = (
        nearest
        if abs(nearest - 35.0 / 365.0) < 1e-12
        else 35.0 / 365.0
    )
    probe_cases.append((time_35, "right"))

probe_cases.append((float(diag_pillars[-1]), "left"))
probe_cases = list(dict.fromkeys(probe_cases))

slice_frames, peak_rows = [], []

for maturity, side in probe_cases:
    label = f"{365.0 * maturity:g}d {side}"
    if maturity == 0.0:
        label += " limit"

    print("Evaluating", label, flush=True)

    variance = np.asarray(
        diag_surface.normalized_variance(
            diag_z, maturity, side
        )
    )

    if (
        not np.all(np.isfinite(variance))
        or np.any(variance < 0.0)
    ):
        raise ValueError(
            f"Invalid local variance in {label}."
        )

    iv = np.full_like(diag_y, np.nan)
    curvature = np.full_like(diag_y, np.nan)
    time_derivative = np.full_like(diag_y, np.nan)

    short_end = (
        maturity < diag_pillars[0]
        or (
            maturity == diag_pillars[0]
            and side == "left"
        )
    )

    if maturity > 0.0:
        iv = np.asarray(
            diag_surface.implied_volatility(
                diag_surface.forward(maturity) * diag_z,
                maturity,
            )
        )
        curvature = np.asarray(
            diag_surface.normalized_call(
                diag_z, maturity, derivative=2
            )
        )
        time_derivative = np.asarray(
            diag_surface.normalized_time_derivative(
                diag_z, maturity, side
            )
        )

    if short_end:
        # Diagnostic identity, not an independent validation:
        # local variance = first-expiry IV squared / g.
        factor = anchor_iv**2 / variance
    else:
        w = iv**2 * maturity
        root_w = np.sqrt(w)
        d1 = -diag_y / root_w + 0.5 * root_w
        phi = (
            np.exp(-0.5 * d1**2)
            / np.sqrt(2.0 * np.pi)
        )
        factor = (
            curvature * diag_z**2 * root_w / phi
        )

    if (
        not np.all(np.isfinite(factor))
        or np.any(factor <= 0.0)
    ):
        raise ValueError(
            f"Invalid density factor in {label}."
        )

    regions, sources, _ = coefficient_regions(
        diag_y, maturity, side
    )

    frame = pd.DataFrame(
        {
            "label": label,
            "days": 365.0 * maturity,
            "time_side": side,
            "log_moneyness": diag_y,
            "region": regions,
            "sources": sources,
            "iv_pct": 100.0 * iv,
            "local_vol_pct": 100.0 * np.sqrt(variance),
            "density_factor": factor,
            "z_squared_curvature": diag_z**2 * curvature,
            "twice_time_derivative": 2.0 * time_derivative,
        }
    )

    peak = frame.loc[frame["local_vol_pct"].idxmax()]

    peak_rows.append(
        {
            "slice": label,
            "peak_lv_pct": peak["local_vol_pct"],
            "peak_y": peak["log_moneyness"],
            "region": peak["region"],
            "sources": sources,
            "iv_at_peak_pct": peak["iv_pct"],
            "g_at_peak": peak["density_factor"],
            "minimum_g": factor.min(),
            "z2_curvature_at_peak": peak[
                "z_squared_curvature"
            ],
            "2cT_at_peak": peak["twice_time_derivative"],
        }
    )
    slice_frames.append(frame)

volatility_slices = pd.concat(
    slice_frames, ignore_index=True
)
volatility_peaks = pd.DataFrame(peak_rows)

display(
    diag_joins[
        [
            "expiry",
            "days",
            "left_log_moneyness",
            "right_log_moneyness",
        ]
    ]
)
display(volatility_peaks)

print(
    "Short-end g is recovered from the variance identity; "
    "it is not an independent validation."
)
print(
    "Day-zero IV and price derivatives are undefined "
    "and remain blank."
)
print(
    "Peaks are sampled, including points immediately "
    "beside the tail joins."
)

Evaluating 0d right limit
Evaluating 0.25d right
Evaluating 1d right
Evaluating 4d left
Evaluating 4d right
Evaluating 7d left
Evaluating 7d right
Evaluating 11d left
Evaluating 11d right
Evaluating 13d left
Evaluating 13d right
Evaluating 35d right
Evaluating 60d left


,expiry,days,left_log_moneyness,right_log_moneyness
0,2023-09-05,4.0,-0.0386,0.0161936
1,2023-09-08,7.0,-0.0826,0.0373002
2,2023-09-12,11.0,-0.0900,0.0602037
3,2023-09-14,13.0,-0.0900,0.0499908
4,2023-09-22,21.0,-0.0900,0.0900000
5,2023-09-29,28.0,-0.0900,0.0900000
6,2023-10-06,35.0,-0.0900,0.0900000
7,2023-10-13,42.0,-0.0900,0.0900000
8,2023-10-27,56.0,-0.0900,0.0900000
9,2023-10-31,60.0,-0.0900,0.0900000


,slice,peak_lv_pct,peak_y,region,sources,iv_at_peak_pct,g_at_peak,minimum_g,z2_curvature_at_peak,2cT_at_peak
0,0d right limit,244.4222051,-0.0900000,Short-end over tail,4d,NaN,0.0158336,0.0157504,NaN,NaN
1,0.25d right,251.7400781,-0.0900000,Short-end over tail,4d,30.7560792,0.0149265,0.0148269,5.0354755e-28,3.1911353e-27
2,1d right,278.4090838,-0.0900000,Short-end over tail,4d,30.7560792,0.0122038,0.0120418,4.7226088e-08,3.6605705e-07
3,4d left,854.5687780,-0.0900000,Short-end over tail,4d,30.7560792,0.0012953,0.0003721,3.0842073e-04,2.2523589e-02
4,4d right,890.5584415,-0.0386001,core + tail,"4d, 7d",14.6806215,0.0003721,0.0003721,4.0429955e-04,3.2064768e-02
5,7d left,1228.6624587,-0.0734400,core + tail,"4d, 7d",22.0824860,0.0001248,0.0001248,8.7748474e-05,1.3246610e-02
6,7d right,1429.4814986,-0.0734400,both cores,"7d, 11d",22.0824860,0.0001248,0.0001248,8.7748474e-05,1.7930675e-02
7,11d left,89.5041385,-0.0861300,core + tail,"7d, 11d",21.9441353,0.0230975,0.0198348,1.7981092e-02,1.4404636e-02
8,11d right,145.4040963,-0.0861300,both cores,"11d, 13d",21.9441353,0.0230975,0.0198348,1.7981092e-02,3.8016256e-02
9,13d left,76.3943329,-0.0864900,both cores,"11d, 13d",21.7931868,0.0637155,0.0634700,6.4843246e-02,3.7843129e-02


Short-end g is recovered from the variance identity; it is not an independent validation.
Day-zero IV and price derivatives are undefined and remain blank.
Peaks are sampled, including points immediately beside the tail joins.


In [12]:
fig = make_subplots(
    rows=2,
    cols=2,
    subplot_titles=(
        "Implied volatility (%)",
        "Local volatility (%), logarithmic scale",
        "Density factor g, logarithmic scale",
        "z squared times call curvature, logarithmic scale",
    ),
)

fields = [
    (1, 1, "iv_pct"),
    (1, 2, "local_vol_pct"),
    (2, 1, "density_factor"),
    (2, 2, "z_squared_curvature"),
]

seen_iv_days = set()

for number, (label, group) in enumerate(
    volatility_slices.groupby("label", sort=False)
):
    color = qualitative.Dark24[
        number % len(qualitative.Dark24)
    ]
    maturity = float(group["days"].iloc[0]) / 365.0
    side = group["time_side"].iloc[0]

    _, _, indices = coefficient_regions(
        diag_y, maturity, side
    )

    joins = diag_joins.loc[
        indices,
        ["left_log_moneyness", "right_log_moneyness"],
    ].to_numpy().ravel()

    join_samples = group["log_moneyness"].isin(joins)

    for row, column, field in fields:
        if field == "iv_pct":
            if (
                maturity == 0.0
                or maturity in seen_iv_days
            ):
                continue
            seen_iv_days.add(maturity)

        values = group[field].to_numpy().copy()

        if (row, column) != (1, 1):
            values[values <= 0.0] = np.nan

        fig.add_trace(
            go.Scatter(
                x=group["log_moneyness"],
                y=values,
                mode="lines",
                name=label,
                legendgroup=label,
                showlegend=(row == 1 and column == 2),
                line={
                    "color": color,
                    "dash": (
                        "dash"
                        if side == "left"
                        else "solid"
                    ),
                },
                customdata=group[
                    ["region", "sources"]
                ].to_numpy(),
                hovertemplate=(
                    "y=%{x:.5f}"
                    "<br>Value=%{y:.6g}"
                    "<br>%{customdata[0]}"
                    "<br>Sources: %{customdata[1]}"
                    "<extra>%{fullData.name}</extra>"
                ),
            ),
            row,
            column,
        )

        if field == "local_vol_pct":
            fig.add_trace(
                go.Scatter(
                    x=group.loc[
                        join_samples, "log_moneyness"
                    ],
                    y=values[join_samples],
                    mode="markers",
                    marker={
                        "color": color,
                        "symbol": "diamond",
                        "size": 7,
                    },
                    legendgroup=label,
                    showlegend=False,
                    name=label + " contributing joins",
                ),
                row,
                column,
            )

for row, column, _ in fields:
    fig.update_xaxes(
        title_text="Forward log-moneyness",
        row=row,
        col=column,
    )
    if (row, column) != (1, 1):
        fig.update_yaxes(
            type="log", row=row, col=column
        )

fig.update_layout(
    height=800,
    title="Current candidate: volatility conditioning",
    legend={"groupclick": "togglegroup"},
)
fig.show()

print(
    "Diamonds mark joins of the slices contributing "
    "to local variance."
)
print(
    "Logarithmic axes retain large values. "
    "Computed zero curvatures cannot appear on a log axis."
)

Diamonds mark joins of the slices contributing to local variance.
Logarithmic axes retain large values. Computed zero curvatures cannot appear on a log axis.


In [13]:
GAMMA_DAYS, GAMMA_LOG_STRIKE = 35.0, 0.0
GAMMA_SPOT_BAND = 0.015

gamma_expiry = GAMMA_DAYS / 365.0
gamma_strike = (
    float(diag_surface.forward(gamma_expiry))
    * np.exp(GAMMA_LOG_STRIKE)
)

gamma_spots = np.sort(
    np.unique(
        np.r_[
            diag_surface.spot
            * np.linspace(
                1.0 - GAMMA_SPOT_BAND,
                1.0 + GAMMA_SPOT_BAND,
                401,
            ),
            diag_surface.spot,
        ]
    )
)

gamma_states = gamma_spots / diag_surface.spot
gamma_a0 = np.asarray(
    diag_surface.normalized_variance(
        gamma_states, 0.0, "right"
    )
)
gamma_anchor_iv = np.asarray(
    diag_surface.implied_volatility(
        diag_surface.forward(diag_pillars[0])
        * gamma_states,
        float(diag_pillars[0]),
    )
)

gamma_environment = pd.DataFrame(
    {
        "spot": gamma_spots,
        "day_zero_lv_pct": 100.0 * np.sqrt(gamma_a0),
        "day_zero_density_factor": (
            gamma_anchor_iv**2 / gamma_a0
        ),
    }
)

gamma_cases = [
    ("N1600_t32", 1.0, 1600, 32),
    ("N3200_t32", 1.0, 3200, 32),
    ("N6400_t32", 1.0, 6400, 32),
    ("N6400_t64", 1.0, 6400, 64),
    ("width0p75_t64", 0.75, 4800, 64),
]

gamma_grids, gamma_frames, gamma_rows = {}, [], []
gamma_target = float(
    diag_surface.call_price(gamma_strike, gamma_expiry)
)

for name, width, intervals, steps in gamma_cases:
    print(
        f"Solving {name}: {intervals} intervals, "
        f"{steps} steps/day, width {width:g}",
        flush=True,
    )

    solver = BackwardVanillaPricer(
        diag_surface,
        -width,
        width,
        intervals,
        max_time_step=1.0 / (365.0 * steps),
    )

    solved = solver.solve(
        gamma_strike, gamma_expiry, kind="call"
    )
    values = solved.greeks(gamma_spots)
    at_spot = solved.greeks(diag_surface.spot)

    frame = pd.DataFrame(
        {
            "case": name,
            "spot": gamma_spots,
            "price": values.price,
            "delta": values.delta,
            "gamma": values.gamma,
        }
    )

    peak = frame.loc[frame["gamma"].idxmax()]

    gamma_rows.append(
        {
            "case": name,
            "width": width,
            "intervals": intervals,
            "steps_per_day": steps,
            "actual_steps": solved.time_steps,
            "gamma_peak_spot": peak["spot"],
            "gamma_peak": peak["gamma"],
            "price_error_at_original_spot": (
                float(at_spot.price) - gamma_target
            ),
            "delta_at_original_spot": float(at_spot.delta),
            "gamma_at_original_spot": float(at_spot.gamma),
        }
    )

    gamma_grids[name] = solved
    gamma_frames.append(frame)

gamma_curves = pd.concat(
    gamma_frames, ignore_index=True
)
gamma_summary = pd.DataFrame(gamma_rows)

comparison_rows = []

comparisons = [
    ("Space 1600 to 3200", "N1600_t32", "N3200_t32"),
    ("Space 3200 to 6400", "N3200_t32", "N6400_t32"),
    ("Time 32 to 64", "N6400_t32", "N6400_t64"),
    (
        "Domain 1.00 to 0.75, same spacing",
        "N6400_t64",
        "width0p75_t64",
    ),
]

for check, early, late in comparisons:
    first = gamma_curves[
        gamma_curves["case"] == early
    ].set_index("spot")
    second = gamma_curves[
        gamma_curves["case"] == late
    ].set_index("spot")

    change = (
        second[["price", "delta", "gamma"]]
        - first[["price", "delta", "gamma"]]
    ).abs()

    peak_early = first["gamma"].idxmax()
    peak_late = second["gamma"].idxmax()

    comparison_rows.append(
        {
            "check": check,
            "max_price_change": change["price"].max(),
            "max_delta_change": change["delta"].max(),
            "max_gamma_change": change["gamma"].max(),
            "gamma_peak_spot_shift": (
                peak_late - peak_early
            ),
        }
    )

gamma_changes = pd.DataFrame(comparison_rows)

display(gamma_summary)
display(gamma_changes)

fig = make_subplots(
    rows=2,
    cols=2,
    subplot_titles=(
        "Delta across spot",
        "Gamma across spot",
        "Day-zero local volatility (%) at these states",
        "Day-zero density factor g at these states",
    ),
)

for name, group in gamma_curves.groupby(
    "case", sort=False
):
    for column, metric in enumerate(
        ("delta", "gamma"), start=1
    ):
        fig.add_trace(
            go.Scatter(
                x=group["spot"],
                y=group[metric],
                mode="lines",
                name=name,
                legendgroup=name,
                showlegend=(column == 1),
            ),
            1,
            column,
        )

node_grid = gamma_grids["N6400_t64"]
h = float(
    node_grid.log_states[1] - node_grid.log_states[0]
)
v = node_grid.normalized_values

node_spots = (
    node_grid.valuation_forward
    * np.exp(node_grid.log_states[1:-1])
)

node_gamma = (
    node_grid.price_scale
    * (
        (v[2:] - 2.0 * v[1:-1] + v[:-2]) / h**2
        - (v[2:] - v[:-2]) / (2.0 * h)
    )
    / node_spots**2
)

selected = (
    (node_spots >= gamma_spots[0])
    & (node_spots <= gamma_spots[-1])
)

node_gamma_check = pd.DataFrame(
    {
        "spot": node_spots[selected],
        "node_fd_gamma": node_gamma[selected],
    }
)
node_gamma_check["interpolated_gamma"] = (
    node_grid.greeks(node_spots[selected]).gamma
)

fig.add_trace(
    go.Scatter(
        x=node_spots[selected],
        y=node_gamma[selected],
        mode="markers",
        marker={"size": 5, "color": "black"},
        name="N6400_t64: node FD gamma",
    ),
    1,
    2,
)

for column, field in enumerate(
    ("day_zero_lv_pct", "day_zero_density_factor"),
    start=1,
):
    fig.add_trace(
        go.Scatter(
            x=gamma_spots,
            y=gamma_environment[field],
            mode="lines",
            name=field,
            showlegend=False,
        ),
        2,
        column,
    )

for row in (1, 2):
    for column in (1, 2):
        fig.add_vline(
            x=diag_surface.spot,
            line_dash="dot",
            row=row,
            col=column,
        )
        fig.update_xaxes(
            title_text="Spot, index points",
            row=row,
            col=column,
        )

fig.update_layout(
    height=750,
    title=(
        "Fixed local-volatility function and carry: "
        "refinement"
    ),
)
fig.show()

print(
    "Node finite differences use the same PDE solution "
    "but a different differentiation formula."
)
print(
    "Grid agreement establishes numerical stability "
    "for this option, not stability to recalibration."
)

Solving N1600_t32: 1600 intervals, 32 steps/day, width 1
Solving N3200_t32: 3200 intervals, 32 steps/day, width 1
Solving N6400_t32: 6400 intervals, 32 steps/day, width 1
Solving N6400_t64: 6400 intervals, 64 steps/day, width 1
Solving width0p75_t64: 4800 intervals, 64 steps/day, width 0.75


,case,width,intervals,steps_per_day,actual_steps,gamma_peak_spot,gamma_peak,price_error_at_original_spot,delta_at_original_spot,gamma_at_original_spot
0,N1600_t32,1.00,1600,32,1124,4567.1639265,0.0164126,-0.0087525,0.4089087,0.0044876
1,N3200_t32,1.00,3200,32,1124,4564.4543145,0.0155221,-0.0002424,0.4087470,0.0044918
2,N6400_t32,1.00,6400,32,1124,4565.4704190,0.0154010,0.0001284,0.4086391,0.0044883
3,N6400_t64,1.00,6400,64,2244,4565.4704190,0.0154050,-0.0001205,0.4086264,0.0044871
4,width0p75_t64,0.75,4800,64,2244,4565.4704190,0.0153970,-0.0001916,0.4086363,0.0044858


,check,max_price_change,max_delta_change,max_gamma_change,gamma_peak_spot_shift
0,Space 1600 to 3200,0.0434422,0.0035264,0.0012403,-2.7096120
1,Space 3200 to 6400,0.0411889,0.0014897,0.0002193,1.0161045
2,Time 32 to 64,0.0039912,0.0000948,0.0000046,0.0000000
3,"Domain 1.00 to 0.75, same spacing",0.0342998,0.0014041,0.0000386,0.0000000


Node finite differences use the same PDE solution but a different differentiation formula.
Grid agreement establishes numerical stability for this option, not stability to recalibration.


In [14]:
input_paths = [MODEL_PATH, tails_path]

input_paths += [
    (tails_path.parent / row["core_file"]).resolve()
    for row in tail_spec["slices"]
]

input_paths += [
    ROOT / "src" / f"{name}.py"
    for name in (
        "black",
        "implied_vol",
        "convex_spline",
        "coupled_tails",
        "short_end",
        "tailed_surface",
        "local_vol",
        "vol_surface",
        "forward_pde",
        "backward_pricer",
    )
]

for saved_audit in (pde_audit, backward_audit):
    verify_inputs(saved_audit)

for name, frame in (
    ("volatility_slices", volatility_slices),
    ("volatility_peaks", volatility_peaks),
    ("gamma_curves", gamma_curves),
    ("gamma_summary", gamma_summary),
    ("gamma_changes", gamma_changes),
    ("node_gamma_check", node_gamma_check),
    ("gamma_environment", gamma_environment),
):
    frame.to_csv(
        DIAG_DIR / f"{name}.csv", index=False
    )

conditioning_audit = {
    "created_utc": datetime.now(timezone.utc).isoformat(),
    "input_sha256": {
        str(path): file_hash(path)
        for path in dict.fromkeys(input_paths)
    },
    "volatility_log_moneyness_domain": [
        DIAG_Y_MIN,
        DIAG_Y_MAX,
    ],
    "volatility_points_per_slice": len(diag_y),
    "probe_cases": [
        {"days": 365.0 * t, "side": side}
        for t, side in probe_cases
    ],
    "short_end_density_factor": (
        "Recovered from first-expiry IV squared "
        "divided by local variance."
    ),
    "gamma_days": GAMMA_DAYS,
    "gamma_strike": gamma_strike,
    "gamma_cases": [
        {
            "name": name,
            "width": width,
            "intervals": n,
            "steps_per_day": steps,
        }
        for name, width, n, steps in gamma_cases
    ],
    "greek_convention": (
        "Original physical local-volatility function "
        "and carry held fixed."
    ),
    "models_refitted": False,
    "volatility_values_clipped": False,
    "scope": (
        "Sampled volatility conditioning and numerical "
        "refinement of one call across spot."
    ),
}

(DIAG_DIR / "conditioning_audit.json").write_text(
    json.dumps(conditioning_audit, indent=2) + "\n"
)

print("Diagnostics saved to:", DIAG_DIR)

Diagnostics saved to: /Users/pranayvij/GitHub/local-vol-spx/outputs/model_conditioning/spx_2023-09-01_combined_central/day_zero_weight_0p1
